In [4]:
import matplotlib.pyplot as plt
params = {'legend.fontsize': 'large',
         'axes.labelsize': 'x-large',
         'axes.titlesize':'x-large',
         'xtick.labelsize':'x-large',
         'ytick.labelsize':'x-large',
         'xtick.direction':'in',
         'ytick.direction':'in',
         }
plt.rcParams.update(params)

from matplotlib import animation # あとでアニメーションのときに使う
from IPython.display import HTML # あとでアニメーションのときに使う

from scipy.integrate import solve_ivp

import numpy as np

## 二重振り子

![double_pendulum](double_pendulum_scheme.gif)

2自由度: 偏角 $\theta_1$ と $\theta_2$.

振り子の支点を原点として、水平右向きを$x$の正方向、 鉛直上向きを$y$の正方向とすると、質点の位置$(x_1,y_1)$と$(x_2,y_2)$はそれぞれ次のように表される：
\begin{align*}
(x_1,y_1) & = (l_1 \sin \theta_1, -l_1 \cos \theta_1)\,, \\
(x_2, y_2) & = (l_1 \sin\theta_1 + l_2 \sin\theta_2, -l_1 \cos\theta_1 - l_2 \cos\theta_2)\,.
\end{align*}

Euler-Lagrange運動方程式は
\begin{align*}
(m_1 + m_2) l_1 \ddot{\theta}_1 + m_2 l_2 \cos(\theta_1 - \theta_2) \ddot{\theta}_2 & =
-m_2 l_1 \dot{\theta}_2^2 \sin(\theta_1 - \theta_2) - (m_1+m_2) g \sin\theta_1, \\
m_2 l_1 \cos(\theta_1 - \theta_2) \ddot{\theta}_1  + m_2 l_2 \ddot{\theta}_2 & =
m_2 l_1 \dot{\theta}_1^2 \sin(\theta_1 - \theta_2) - m_2 g \sin\theta_2.
\end{align*}

これは $ \ddot{\theta}_{1,2}$ の2階の連立微分方程式である。数値的に簡単に解ける。

まず $\omega_1 := \dot{\theta}_1$, $\omega_2 := \dot{\theta}_2$ と定義して、以下のように運動方程式を書き直す：

\begin{align*}
\frac{d}{dt}
\begin{pmatrix}
\theta_1\\
\theta_2\\
\omega_1\\
\omega_2
\end{pmatrix}
=
\begin{pmatrix}
\omega_1\\
\omega_2\\
\frac{g\left(\cos(\theta_1 - \theta_2) \sin \theta_2 - \frac{m_1+m_2}{m_2}\sin\theta_1\right) - \left(l_1 \omega_1^2 \cos(\theta_1 - \theta_2) + l_2 \omega_2^2\right)\sin(\theta_1-\theta_2)}
{l_1 \left(\frac{m_1+m_2}{m_2} - \cos^2(\theta_1 - \theta_2)\right)}\\
\frac{g\frac{m_1+m_2}{m_2}\left(\cos(\theta_1 - \theta_2) \sin \theta_1 - \sin\theta_2\right) - \left(\frac{m_1+m_2}{m_2}l_1 \omega_1^2 + l_2 \omega_2^2 \cos(\theta_1 - \theta_2) \right)\sin(\theta_1-\theta_2)}
{l_2 \left(\frac{m_1+m_2}{m_2} - \cos^2(\theta_1 - \theta_2)\right)}
\end{pmatrix}
\end{align*}
この方程式は $d\boldsymbol{y} /dt = f(t, \boldsymbol{y})$ という形になっているので、ODEソルバーで解ける。

In [6]:
g = 9.81 # 重力加速度
l1 = 0.4 # [m], 振り子1の長さ
l2 = 0.4 # [m], 振り子2の長さ
# m1 = 1.0 # 振り子1の重さ -> f_doubplependulum でデフォルト m1=1.0 kg に設定。
# m2 = 1.0 # 振り子2の重さ -> f_doubplependulum でデフォルト m2=1.0 kg に設定。

# 微分方程式の右辺
def f_doublependulum(t, xin, len1, len2, m1=1.0, m2=1.0):
    theta1 = xin[0]
    theta2 = xin[1]
    omega1 = xin[2]
    omega2 = xin[3]
    a1 = (m1 + m2)*len1
    b1 = m2*len2*np.cos(theta1 - theta2)
    c1 = m2*len2*omega2*omega2*np.sin(theta1 - theta2) + (m1 + m2)*g*np.sin(theta1)
    a2 = m2*len1*np.cos(theta1 - theta2)
    b2 = m2*len2
    c2 = -m2*len1*omega1*omega1*np.sin(theta1 - theta2) + m2*g*np.sin(theta2)
    domega1 = - ( c2/b2 - c1/b1 ) / ( a2/b2 - a1/b1 )
    domega2 = - ( c2/a2 - c1/a1 ) / ( b2/a2 - b1/a1 )
    return np.array([omega1,
                     omega2,
                     domega1,
                     domega2
                    ])

# 質点1の位置 (x_1, y_1) を計算：
def calcpos1(theta1, len1):
    return np.array([len1*np.sin(theta1), -len1*np.cos(theta1)])

# 質点2の位置 (x_2, y_2) を計算：
def calcpos2(theta1, theta2, len1, len2):
    return np.array([len1*np.sin(theta1) + len2*np.sin(theta2), -len1*np.cos(theta1) - len2*np.cos(theta2)])

In [9]:
# 初期条件：ここを変えてカオス的な振る舞いを見てみよう。
theta1_0 = np.pi / 2.
theta2_0 = np.pi / 2.
omega1_0 = 0.
omega2_0 = 0.
y0 = np.array([theta1_0, theta2_0, omega1_0, omega2_0])
t0 = 0.
# 終端時刻：
tend = 15. # 秒
fps = 24 # 1秒あたりのフレーム数
dt = 1./fps
ts = np.arange(t0, tend, dt)

# 微分方程式を解く：
sol = solve_ivp(f_doublependulum, [t0, tend], y0, t_eval=ts, args=(l1,l2))
qs = sol.y

In [ ]:
# 可視化（終端時刻、fps によりますが、アニメーションの生成には20秒くらいかかります）

# 図の準備
fig, ax = plt.subplots()
ax.set_xlabel("x [cm]") #x軸ラベル
ax.set_ylabel("y [cm]") #y軸ラベル
ax.set_xlim(-1.1*(l1+l2)*1.e2,1.1*(l1+l2)*1.e2)
ax.set_ylim(-1.1*(l1+l2)*1.e2,1.1*(l1+l2)*1.e2)
ax.axhline(y = 0., color = 'black', linestyle = '--')
ax.set_aspect('equal')

# プロット要素を準備
point1, = ax.plot([], [], 'bo', markersize=10)
rod1, = ax.plot([], [], 'b')
point2, = ax.plot([], [], 'ro', markersize=10)
rod2, = ax.plot([], [], 'r')
title = ax.set_title(None)

# 初期化
def init():
    rod1.set_data([], [])
    point1.set_data([], [])
    rod2.set_data([], [])
    point2.set_data([], [])
    title.set_text(None)
    return point1, rod1, point2, rod2

# フレーム更新関数
def update(frame):
    theta1now = qs[0][frame]
    theta2now = qs[1][frame]
    pos1 = calcpos1(theta1now, l1) * 1e2
    pos2 = calcpos2(theta1now, theta2now, l1, l2) * 1e2

    # 現在位置
    rod1.set_data([0., pos1[0]], [0., pos1[1]])
    point1.set_data([pos1[0]], [pos1[1]])
    rod2.set_data([pos1[0], pos2[0]], [pos1[1], pos2[1]])
    point2.set_data([pos2[0]], [pos2[1]])

    title.set_text("Double Pendulum, t = %.2f s" % ts[frame])

    return rod1, point1, rod2, point2

# アニメーション作成
ani = animation.FuncAnimation(
    fig, update, frames=len(ts), init_func=init,
    interval=1e3/fps, blit=False
)
plt.close()

HTML(ani.to_jshtml()) # これで jupyter notebook 上でインタラクティブに表示